# Distance from fire points to the nearest road

In [8]:
import geopandas as gpd

In [9]:
# Reproject to a metric CRS (SIRGAS 2000 / Brazil Polyconic) to get distances in meters
fires = gpd.read_file("bdqueimadas_2026-10-01_2026-10-02.geojson").to_crs(5880)
roads = gpd.read_file("roads.gpkg").to_crs(5880)

# Keep only fire points inside the roads bounding box
xmin, ymin, xmax, ymax = roads.total_bounds
fires = fires.cx[xmin:xmax, ymin:ymax]

In [10]:
fires = gpd.sjoin_nearest(fires, roads[["geometry"]], distance_col="dist_to_road")
fires = fires[~fires.index.duplicated()].drop(columns="index_right")
fires[["Municipio", "dist_to_road"]].head()

,Municipio,dist_to_road
37,ALTAMIRA,4887.242371
199,APIACÁS,2987.690045
213,ALTAMIRA,8424.474816
218,NOVA BANDEIRANTES,3972.666279
234,ALTAMIRA,6157.435331


In [11]:
fires

,DataHora,Satelite,Pais,Estado,Municipio,Bioma,DiaSemChuva,Precipitacao,RiscoFogo,FRP,Latitude,Longitude,geometry,dist_to_road
37,2026-10-01 00:00:00,GOES-19,Brasil,PARÁ,ALTAMIRA,Amazônia,2.0,0.0,0.83,55.4,-7.49770,-54.98540,POINT (4891237.541 9170777.85),4887.242371
199,2026-10-01 00:18:00,TERRA_M-M,Brasil,MATO GROSSO,APIACÁS,Amazônia,3.0,0.0,0.63,15.1,-9.34819,-57.17641,POINT (4651073.51 8964667.959),2987.690045
213,2026-10-01 00:18:00,TERRA_M-M,Brasil,PARÁ,ALTAMIRA,Amazônia,3.0,0.0,0.75,8.2,-8.18275,-54.78931,POINT (4913023.119 9095051.548),8424.474816
218,2026-10-01 00:18:00,TERRA_M-M,Brasil,MATO GROSSO,NOVA BANDEIRANTES,Amazônia,3.0,0.0,0.79,9.5,-9.70286,-58.13390,POINT (4546367.304 8924252.728),3972.666279
234,2026-10-01 00:18:00,TERRA_M-M,Brasil,PARÁ,ALTAMIRA,Amazônia,2.0,0.0,0.71,10.6,-8.22401,-54.74995,POINT (4917368.855 9090496.235),6157.435331
...,...,...,...,...,...,...,...,...,...,...,...,...,...,...
34481,2026-10-02 07:26:00,AQUA_M-M,Brasil,PARÁ,ALTAMIRA,Amazônia,NaN,NaN,NaN,45.6,-7.39526,-55.20736,POINT (4866708.058 9182048.266),3731.556284
34482,2026-10-02 07:26:00,AQUA_M-M,Brasil,PARÁ,SÃO FÉLIX DO XINGU,Amazônia,NaN,NaN,NaN,12.5,-6.23534,-53.14690,POINT (5094408.537 9310428.189),1828.676863
34484,2026-10-02 07:26:00,AQUA_M-M,Brasil,PARÁ,NOVO PROGRESSO,Amazônia,NaN,NaN,NaN,4.3,-7.41477,-55.57948,POINT (4825634.015 9179761.206),3287.293087
34485,2026-10-02 07:26:00,AQUA_M-M,Brasil,PARÁ,ITAITUBA,Amazônia,NaN,NaN,NaN,7.0,-7.84580,-56.60373,POINT (4712851.269 9131511.443),15036.652149


In [12]:
esri_tiles = "https://server.arcgisonline.com/ArcGIS/rest/services/World_Street_Map/MapServer/tile/{z}/{y}/{x}"
esri_attr = "Tiles &copy; Esri &mdash; Esri, HERE, Garmin, © OpenStreetMap contributors, and the GIS user community"

m = roads.explore(color="gray", tiles=esri_tiles, attr=esri_attr)
fires.explore(m=m, column="dist_to_road", cmap="YlOrRd_r", marker_kwds={"radius": 3},
              tooltip=["Municipio", "dist_to_road"], legend_kwds={"caption": "Distance to road (m)"})